In [40]:
import pandas as pd
import requests
from io import BytesIO

# GitHub raw 파일 URL
url = 'https://raw.githubusercontent.com/aaqq8/SteadyEstate/main/%EC%84%9C%EC%9A%B8%EC%8B%9C_%EC%95%84%ED%8C%8C%ED%8A%B8_%EB%A7%A4%EB%A7%A4.xlsx'

# 파일 가져오기
response = requests.get(url)
if response.status_code == 200:
    # 엑셀 파일을 pandas로 읽기 (openpyxl 엔진 사용)
    file_decoded = BytesIO(response.content)
    df = pd.read_excel(file_decoded, engine='openpyxl')

# 주소에서 구 이름만 추출
df['gu'] = df['address'].apply(lambda x: x.split()[1])

# 구별 매물 수 집계
gu_counts = df['gu'].value_counts().reset_index()
gu_counts.columns = ['gu', 'count']

# count를 높은 순서대로 출력
sorted_gu_counts = gu_counts.sort_values(by='count', ascending=False)
sorted_gu_counts

,gu,count
0,은평구,403
1,강서구,388
2,강남구,351
3,구로구,347
4,성북구,344
5,양천구,343
6,마포구,336
7,강동구,312
8,송파구,297
9,동대문구,248


In [35]:
import pandas as pd
import folium
import json
from folium.plugins import MarkerCluster
from io import BytesIO
import requests

# GitHub raw 파일 URL
url = 'https://raw.githubusercontent.com/aaqq8/SteadyEstate/main/%EC%84%9C%EC%9A%B8%EC%8B%9C_%EC%95%84%ED%8C%8C%ED%8A%B8_%EB%A7%A4%EB%A7%A4.xlsx'

# 파일 가져오기
response = requests.get(url)
if response.status_code == 200:
    # 엑셀 파일을 pandas로 읽기 (openpyxl 엔진 사용)
    file_decoded = BytesIO(response.content)
    df = pd.read_excel(file_decoded, engine='openpyxl')

# 주소에서 구 이름만 추출
df['gu'] = df['address'].apply(lambda x: x.split()[1])

# 구별 매물 수 집계
gu_counts = df['gu'].value_counts().reset_index()
gu_counts.columns = ['gu', 'count']

# 서울시 구 경계 GeoJSON 데이터 로드
geo_json_url = 'https://raw.githubusercontent.com/southkorea/southkorea-maps/master/kostat/2013/json/skorea_municipalities_geo_simple.json'
geo_json_data = requests.get(geo_json_url).json()

# Folium 지도 객체 생성
m = folium.Map(location=[37.5665, 126.9780], zoom_start=11)

# Choropleth 레이어 추가
folium.Choropleth(
    geo_data=geo_json_data,
    name='choropleth',
    data=gu_counts,
    columns=['gu', 'count'],
    key_on='feature.properties.name',  # GeoJSON 파일의 지역명에 해당하는 속성명
    fill_color='YlGnBu',
    fill_opacity=0.7,
    line_opacity=0.2,
    legend_name='Number of Listings by District (구)'
).add_to(m)

# 마커 클러스터링 (옵션)
marker_cluster = MarkerCluster().add_to(m)
for idx, row in df.iterrows():
    folium.Marker(
        location=[row['lat'], row['lng']],
        popup=f"Price: {row['pricePerSize']}, Address: {row['address']}",
        icon=folium.Icon(color='blue', icon='info-sign')
    ).add_to(marker_cluster)

# 지도 표시 (Jupyter Notebook 환경에서 사용 가능)
m

In [39]:
# 지도 저장
m.save('서울 아파트 매매.html')